<a href="https://colab.research.google.com/github/amomen1218/Solar-Potential-Area/blob/main/Building_Footprint.ipynb" target="_parent"><img src="https://colab.research.google.com/assets/colab-badge.svg" alt="Open In Colab"/></a>

In [4]:
import os

# List the contents of the directory
directory_path = "/content/drive/MyDrive/Solar_IWM/Data/Building Footprint"
if os.path.isdir(directory_path):
    print(f"Contents of '{directory_path}':")
    for item in os.listdir(directory_path):
        print(item)
else:
    print(f"The path '{directory_path}' is not a directory or does not exist.")

Contents of '/content/drive/MyDrive/Solar_IWM/Data/Building Footprint':
Building_Footprint_Merge.gdb


In [6]:
import geopandas as gpd

# Define the path to the geodatabase file
geodatabase_path = "/content/drive/MyDrive/Solar_IWM/Data/Building Footprint/Building_Footprint_Merge.gdb"

# Load the geodatabase file
try:
    gdf = gpd.read_file(geodatabase_path)
    print(f"Successfully loaded {len(gdf)} features from the geodatabase.")
except Exception as e:
    print(f"Error loading geodatabase: {e}")
    gdf = None

Successfully loaded 7204 features from the geodatabase.


/usr/local/lib/python3.13/dist-packages/pyogrio/geopandas.py:382: UserWarning: More than one layer found in 'Building_Footprint_Merge.gdb': 'Building_Merge' (default), 'UnIdentified_merge', 'Road_merge'. Specify layer parameter to avoid this warning.
  result = read_func(


In [7]:
if gdf is not None:
    # Ensure WGS84 for web tiles (common for interactive maps)
    if gdf.crs != "EPSG:4326":
        print("Converting CRS to EPSG:4326 for web mapping.")
        gdf = gdf.to_crs(epsg=4326)
    else:
        print("CRS is already EPSG:4326.")

    # Display the first few rows and geometry type to inspect data
    display(gdf.head())
    print(f"Geometry type: {gdf.geometry.geom_type.unique()}")

Converting CRS to EPSG:4326 for web mapping.


,Shape_Length,Shape_Area,geometry
0,52.340745,141.533753,"MULTIPOLYGON (((90.33957 23.76431, 90.33961 23..."
1,74.216192,337.533271,"MULTIPOLYGON (((90.33962 23.76432, 90.33983 23..."
2,74.848870,341.342717,"MULTIPOLYGON (((90.33984 23.76435, 90.34005 23..."
3,52.266866,154.301603,"MULTIPOLYGON (((90.34005 23.76439, 90.34014 23..."
4,46.623582,102.879628,"MULTIPOLYGON (((90.33951 23.76414, 90.33953 23..."


Geometry type: ['MultiPolygon']


Now, let's create an interactive map using `gdf.explore()`.

In [18]:
from google.colab import drive
drive.mount('/content/drive')

Drive already mounted at /content/drive; to attempt to forcibly remount, call drive.mount("/content/drive", force_remount=True).


In [17]:
if gdf is not None:
    print("Available columns in the GeoDataFrame:")
    print(gdf.columns.tolist())
else:
    print("GeoDataFrame (gdf) is not loaded or is empty.")

Available columns in the GeoDataFrame:
['Shape_Length', 'Shape_Area', 'geometry']


In [20]:
if gdf is not None and not gdf.empty:
    # Launch an interactive Leaflet map directly from GeoPandas
    # Using 'Shape_Length' column for coloring
    if 'Shape_Length' in gdf.columns:
        column_to_map = 'Shape_Length'
    else:
        column_to_map = None # No specific column for coloring
        print("No 'Shape_Length' column found for coloring. Mapping with default style.")

    m = gdf.explore(
        column=column_to_map,
        cmap="viridis",
        tiles="Esri WorldImagery",  # Changed to Esri WorldImagery
        style_kwds={"weight": 1, "fillOpacity": 0.6},
        legend=True
    )

    # Save the map to an HTML file and display it inline
    map_filename = "buildings_map_shape_length.html"
    m.save(map_filename)
    print(f"Interactive map saved to {map_filename}")

    # Display the map (works in Jupyter/Colab notebooks)
    m
else:
    print("Cannot create map: GeoDataFrame is empty or not loaded.")

Interactive map saved to buildings_map_shape_length.html


In [24]:
m

In [25]:
if gdf is not None and not gdf.empty:
    # Re-project to Web Mercator (EPSG:3857)
    gdf_web_mercator = gdf.to_crs(epsg=3857)
    print("GeoDataFrame re-projected to EPSG:3857 (Web Mercator).")

    # Use 'Shape_Length' for coloring
    if 'Shape_Length' in gdf_web_mercator.columns:
        column_to_map = 'Shape_Length'
    else:
        column_to_map = None
        print("No 'Shape_Length' column found for coloring in re-projected data.")

    # Launch an interactive Leaflet map with Esri WorldImagery tiles
    m_web_mercator = gdf_web_mercator.explore(
        column=column_to_map,
        cmap="viridis",
        tiles="Esri WorldImagery",
        style_kwds={"weight": 1, "fillOpacity": 0.6},
        legend=True
    )

    # Save and display the new map
    map_filename_web_mercator = "buildings_map_shape_length_web_mercator.html"
    m_web_mercator.save(map_filename_web_mercator)
    print(f"Interactive map saved to {map_filename_web_mercator}")

    # Display the map
    m_web_mercator
else:
    print("Cannot create map: GeoDataFrame is empty or not loaded.")

GeoDataFrame re-projected to EPSG:3857 (Web Mercator).
Interactive map saved to buildings_map_shape_length_web_mercator.html


Since the direct re-projection with `gdf.explore` didn't fully resolve the distortion, let's try creating a `folium.Map` explicitly, setting its CRS, and then adding the re-projected GeoDataFrame.

In [29]:
import folium

if gdf_web_mercator is not None and not gdf_web_mercator.empty:
    # Get the centroid of the re-projected data for initial map centering
    centroid_web_mercator = gdf_web_mercator.to_crs(epsg=4326).geometry.centroid.iloc[0]
    start_coords = (centroid_web_mercator.y, centroid_web_mercator.x)

    # Create a Folium map, explicitly setting the CRS for the map itself
    # Use a direct URL for Esri WorldImagery and specify crs='EPSG3857'
    m_explicit_crs = folium.Map(
        location=start_coords,
        zoom_start=14, # Adjust zoom as needed
        tiles='https://server.arcgisonline.com/ArcGIS/rest/services/World_Imagery/MapServer/tile/{z}/{y}/{x}',
        attr='Esri',
        crs='EPSG3857' # Crucial for aligning with the Web Mercator data
    )

    # Add the re-projected GeoDataFrame to this map
    # Note: folium.GeoJson will automatically handle the CRS if it's different from the map, but it's good practice
    # to ensure the data is already in the map's CRS (which gdf_web_mercator is).
    folium.GeoJson(
        gdf_web_mercator.__geo_interface__,
        style_function=lambda x: {
            'fillColor': '#FFFF00' if x['properties']['Shape_Length'] > gdf_web_mercator['Shape_Length'].mean() else '#0000FF',
            'color': 'black',
            'weight': 1,
            'fillOpacity': 0.6
        }
    ).add_to(m_explicit_crs)

    print("Explicit Folium map created with EPSG:3857 CRS.")
    # Display the map
    m_explicit_crs
else:
    print("Cannot create map: GeoDataFrame is empty or not loaded.")

/tmp/ipykernel_1095/1208349922.py:5: UserWarning: Geometry is in a geographic CRS. Results from 'centroid' are likely incorrect. Use 'GeoSeries.to_crs()' to re-project geometries to a projected CRS before this operation.

  centroid_web_mercator = gdf_web_mercator.to_crs(epsg=4326).geometry.centroid.iloc[0]


Explicit Folium map created with EPSG:3857 CRS.


In [30]:
m